In [0]:
%python
from pyspark.sql import SparkSession
from pyspark.sql.types import *
from pyspark.sql.functions import *

In [0]:
%sql
CREATE OR REPLACE TEMP VIEW customers_tmp_view AS
SELECT *
FROM read_files(
  '/Volumes/manideeppateru_db_workspace_7405606170578073/dine_dash/dinedash/dim_customers.csv',
  format => 'csv',
  header => true,
  inferSchema => true
);

In [0]:
create or replace temp view delivery_agents_view as select * from read_files('/Volumes/manideeppateru_db_workspace_7405606170578073/dine_dash/dinedash/dim_delivery_agents.csv', format => 'csv', header => true, inferSchema => true);

In [0]:
create or replace temp view menu_items_view as select * from read_files('/Volumes/manideeppateru_db_workspace_7405606170578073/dine_dash/dinedash/dim_menu_items.csv', format => 'csv', header => true, inferSchema => true);

In [0]:
create or replace temp view locations_view as select * from read_files('/Volumes/manideeppateru_db_workspace_7405606170578073/dine_dash/dinedash/dim_locations.csv', format => 'csv', header => true, inferSchema => true)

In [0]:
create or replace temp view restaurants_view as select * from read_files('/Volumes/manideeppateru_db_workspace_7405606170578073/dine_dash/dinedash/dim_restaurants.csv', format => 'csv', header => true, inferSchema => true);

In [0]:
CREATE OR REPLACE TABLE customers_bronze
AS
SELECT *,
       current_timestamp() AS ingestion_timestamp,
       _metadata.file_name AS source_file_name
FROM READ_FILES(
    '/Volumes/manideeppateru_db_workspace_7405606170578073/dine_dash/dinedash/dim_customers.csv',
    format => 'csv',
    header => true,
    schema => 'customer_id STRING,
               name STRING,
               email STRING,
               signup_date DATE,
               dob DATE,
               location_id STRING'
);

num_affected_rows,num_inserted_rows


In [0]:
CREATE OR REPLACE TABLE restaurants_bronze
AS
SELECT *,
       current_timestamp() AS ingestion_timestamp,
       _metadata.file_name AS source_file_name
FROM READ_FILES(
    '/Volumes/manideeppateru_db_workspace_7405606170578073/dine_dash/dinedash/dim_restaurants.csv',
    format => 'csv',
    header => true,
    schema => 'restaurant_id STRING,
               name STRING,
               cuisine STRING,
               location_id STRING,
               rating DOUBLE,
               delivery_fee DOUBLE'
);

num_affected_rows,num_inserted_rows


In [0]:
CREATE OR REPLACE TABLE locations_bronze
AS
SELECT *,
       current_timestamp() AS ingestion_timestamp,
       _metadata.file_name AS source_file_name
FROM READ_FILES(
    '/Volumes/manideeppateru_db_workspace_7405606170578073/dine_dash/dinedash/dim_locations.csv',
    format => 'csv',
    header => true,
    schema => 'location_id STRING,
               area STRING,
               city STRING,
               state STRING,
               latitude DOUBLE,
               longitude DOUBLE'
);

num_affected_rows,num_inserted_rows


In [0]:
CREATE OR REPLACE TABLE delivery_agents_bronze
AS
SELECT *,
       current_timestamp() AS ingestion_timestamp,
       _metadata.file_name AS source_file_name
FROM READ_FILES(
    '/Volumes/manideeppateru_db_workspace_7405606170578073/dine_dash/dinedash/dim_delivery_agents.csv',
    format => 'csv',
    header => true,
    schema => 'agent_id STRING,
               name STRING,
               phone STRING,
               rating DOUBLE'
);

num_affected_rows,num_inserted_rows


In [0]:
CREATE OR REPLACE TABLE menu_items_bronze
AS
SELECT *,
       current_timestamp() AS ingestion_timestamp,
       _metadata.file_name AS source_file_name
FROM READ_FILES(
    '/Volumes/manideeppateru_db_workspace_7405606170578073/dine_dash/dinedash/dim_menu_items.csv',
    format => 'csv',
    header => true,
    schema => 'item_id STRING,
               restaurant_id STRING,
               item_name STRING,
               price DOUBLE,
               category STRING'
);

num_affected_rows,num_inserted_rows


In [0]:
create or replace table customer_filter_bronze as select * from customers_bronze where customer_id is not null and email is not null and location_id is not null and signup_date is not null and dob is not null and name is not null;

num_affected_rows,num_inserted_rows


In [0]:
create or replace table restaurants_filter_bronze as select * from restaurants_bronze where restaurant_id is not null and name is not null and cuisine is not null and location_id is not null and rating is not null and delivery_fee is not null;

num_affected_rows,num_inserted_rows


In [0]:
create or replace table locations_filter_bronze as select * from locations_bronze where location_id is not null and area is not null and city is not null and state is not null and latitude is not null and longitude is not null; 

num_affected_rows,num_inserted_rows


In [0]:
create or replace table delivery_agents_filter_bronze as select * from delivery_agents_bronze where agent_id is not null and name is not null and phone is not null and rating is not null;

num_affected_rows,num_inserted_rows


In [0]:
CREATE OR REPLACE TABLE menu_items_filter_bronze

AS
SELECT *
FROM menu_items_bronze
WHERE item_id IS NOT NULL
  AND restaurant_id IS NOT NULL
  AND item_name IS NOT NULL
  AND price IS NOT NULL
  AND category IS NOT NULL;

num_affected_rows,num_inserted_rows


In [0]:
create table if not exists  orders_bronze;

In [0]:
COPY INTO orders_bronze
FROM '/Volumes/manideeppateru_db_workspace_7405606170578073/dine_dash/dinedash/orders/'
FILEFORMAT = JSON
COPY_OPTIONS (
    'mergeSchema'= 'true'
);

num_affected_rows,num_inserted_rows,num_skipped_corrupt_files
0,0,0


In [0]:
 select count(*) as count_files from orders_bronze;

count_files
16651


In [0]:
select count(*) as Total_orders from orders_bronze;

Total_orders
16651


In [0]:
select payment_method, count(*) as orders_count from orders_bronze group by payment_method;

payment_method,orders_count
wallet,4140
cash,4201
card,4186
UPI,4124


In [0]:
select order_status, count(*) as orders_count from orders_bronze group by order_status;

order_status,orders_count
cancelled,4129
en route,4238
delivered,4105
preparing,4179


In [0]:
select r.restaurant_id, r.name , count(*) as orders_count from restaurants_filter_bronze r inner join orders_bronze b on r.restaurant_id=b.restaurant_id group by r.restaurant_id, r.name ;

restaurant_id,name,orders_count
R180,Curry Leaf Express,103
R182,Spice Villa Hub,77
R130,Tasty Bites Express,78
R069,Food Haven Grill,88
R057,Tasty Bites Grill,83
R065,Tasty Bites Hub,91
R137,Tasty Bites Hub,86
R010,Pasta Palace Hub,86
R150,Pasta Palace Hub,87
R140,Food Haven Corner,94


In [0]:
select c.name , count(*) as orders_count from customer_filter_bronze c join orders_bronze b on c.customer_id=b.customer_id group by c.name;

name,orders_count
Bill Williams,3
Dylan Jones,2
Jennifer Montgomery,8
Lisa Barrera,3
Ashley Moreno,1
Tara Cabrera,2
Kaitlyn Burns,1
Elizabeth Perez MD,2
Tracy Smith,2
Adam Williams,2


In [0]:
select a.name, count(*) as orders_count from delivery_agents_filter_bronze a join orders_bronze b on a.agent_id=b.agent_id group by a.name;

name,orders_count
Eric Joyce,39
Tiffany Chaney,48
Olivia Johnson,50
Sara Castillo,37
Jessica Travis,41
Colleen Calderon,134
Theresa Wagner,39
James Anderson,32
Sarah Melendez,37
Matthew Conley,39


In [0]:
select * from orders_bronze order by total_amount desc limit 10;

agent_id,customer_id,delivery_location_id,items_ordered,order_id,order_status,payment_method,restaurant_id,timestamp,tip,total_amount
A057,C5726,L100,"List(List(I0225, Continue Soda, 27.93, 5), List(I0290, President Spring Roll, 22.69, 4), List(I0058, Huge Wrap, 26.21, 5))",c12860c3-683a-47f7-b790-7cbbbcfc0fec,en route,cash,R159,2024-03-21T10:26:52,1.57,361.46
A339,C5959,L063,"List(List(I0102, Continue Biryani, 29.21, 5), List(I0208, Large Soda, 26.72, 5), List(I0323, Leave Pasta, 15.25, 5))",05e56a7c-190c-4bde-ac13-e34b38fe155a,delivered,cash,R151,2024-01-13T10:47:27,0.14,355.9
A188,C6763,L073,"List(List(I0030, Address Brownie, 26.63, 5), List(I0281, Bag Ice Cream, 29.82, 5), List(I0190, Picture Juice, 17.55, 4))",341cb220-46e4-4f0d-b2f2-2e494b5729dd,en route,card,R147,2024-02-01T03:45:45,2.66,352.45
A357,C3608,L002,"List(List(I0088, Magazine Wrap, 18.12, 5), List(I0206, Across Pasta, 27.41, 5), List(I0041, Recognize Pasta, 24.26, 5))",3b6f5bd2-08e4-412d-be9e-7701463015b0,preparing,card,R105,2024-03-20T15:31:24,3.94,348.95
A063,C4740,L070,"List(List(I0013, Tough Garlic Bread, 28.94, 5), List(I0309, Middle Pizza, 26.67, 3), List(I0258, Take Biryani, 23.64, 5))",f43228bd-94e5-4ef6-914a-c7ebdceaa572,delivered,wallet,R056,2024-01-23T01:11:42,3.5,342.91
A273,C0287,L085,"List(List(I0102, Continue Biryani, 29.21, 5), List(I0323, Leave Pasta, 15.25, 4), List(I0208, Large Soda, 26.72, 5))",621d746e-bd7d-4e27-b06e-a098a9bffda7,delivered,cash,R151,2024-03-13T09:05:24,1.5,340.65
A338,C6393,L086,"List(List(I0294, Especially Garlic Bread, 18.39, 5), List(I0086, Image Pasta, 28.23, 5), List(I0308, Special Ice Cream, 20.15, 5))",75dfeba8-60e0-42c2-9149-315f030e8d9d,cancelled,card,R050,2024-01-14T20:53:27,2.38,333.85
A344,C3804,L099,"List(List(I0418, Huge Brownie, 28.96, 5), List(I0253, Seem Garlic Bread, 29.66, 5), List(I0072, Commercial Pizza, 9.97, 4))",72559328-7d0d-4177-8c44-4ebc43dca731,preparing,wallet,R171,2024-03-17T21:42:44,4.48,332.98
A248,C0791,L075,"List(List(I0460, Clear Tea, 29.07, 5), List(I0052, To Nachos, 28.81, 5), List(I0060, Sign Cake, 7.68, 5))",b9dc92fc-1922-4274-a42c-85b83e46bea2,delivered,wallet,R091,2024-02-13T05:12:39,4.03,327.8
A222,C5690,L095,"List(List(I0222, Oil Juice, 29.46, 4), List(I0105, Section Brownie, 29.74, 4), List(I0083, Impact Coffee, 22.66, 4))",7d9b6852-ffb2-4bac-84e4-cc7960284e30,preparing,card,R122,2024-02-17T00:31:34,1.66,327.44


In [0]:
select payment_method ,round(avg(tip),2) from orders_bronze group by payment_method; 

payment_method,"round(avg(tip), 2)"
wallet,2.5
cash,2.47
card,2.51
UPI,2.53


In [0]:
SELECT
    ROUND(
        COUNT_IF(tip > total_amount * 0.10) * 100.0 / COUNT(*),
        2
    ) AS percentage_orders
FROM orders_bronze;

percentage_orders
21.49


In [0]:
SELECT
    order_status,
    ROUND(
        COUNT(*) * 100.0 / SUM(COUNT(*)) OVER (),
        2
    ) AS percentage
FROM orders_bronze
GROUP BY order_status;

order_status,percentage
cancelled,24.80
en route,25.45
delivered,24.65
preparing,25.10


In [0]:
select c.name , count(*) as orders_count from customer_filter_bronze c join orders_bronze b on c.customer_id=b.customer_id group by c.name order by orders_count desc limit 10;

name,orders_count
Jose Alexander,12
David Smith,12
Michael Williams,12
Paul Hill,12
Daniel Jones,12
Lori Mcdowell,12
Erin Taylor,12
Wayne Peters,12
Jessica Smith,11
Mark Brown,11


In [0]:
select r.name , count(*) as orders_count from restaurants_filter_bronze r inner join orders_bronze b on r.restaurant_id=b.restaurant_id group by  r.name order by orders_count desc limit 10;

name,orders_count
Spice Villa Grill,1019
Curry Leaf Corner,1005
Spice Villa Hub,874
Spice Villa Corner,725
Curry Leaf Kitchen,641
Food Haven Grill,641
Tasty Bites Grill,605
Tasty Bites Hub,528
Pasta Palace Hub,523
Food Haven Kitchen,497


In [0]:
select * from orders_bronze

agent_id,customer_id,delivery_location_id,items_ordered,order_id,order_status,payment_method,restaurant_id,timestamp,tip,total_amount
A052,C7420,L049,"List(List(I0117, Over Juice, 0.0, 5))",47b006aa-585e-4407-a621-2da8e9a4da59,delivered,cash,R078,2024-01-19T21:20:41,4.87,0.0
A270,C9458,L020,"List(List(I0329, Job Ice Cream, 6.66, 3), List(I0251, Follow Tea, 24.58, 3))",b293cb14-bdc2-4f3c-8ef3-4ee49cfe89a5,cancelled,cash,R144,2024-01-14T11:51:29,3.19,93.72
A388,C5695,L025,"List(List(I0052, To Nachos, 28.81, 3))",d2e4886a-83f1-489c-b093-10d1df8684eb,preparing,card,R091,2024-01-11T10:47:36,4.8,86.43
A018,C5784,L093,"List(List(I0228, Laugh Juice, 6.07, 1), List(I0097, Attack Biryani, 18.79, 5), List(I0211, Specific Spring Roll, 21.36, 1))",2c994810-bb0b-4def-82fc-2bdd72235c06,preparing,card,R175,2024-01-10T11:32:48,1.34,121.38
A279,C2581,L052,"List(List(I0255, Finish Garlic Bread, 0.0, 3))",8d5c0270-595d-4890-b868-950ee1636d6e,preparing,cash,R082,2024-01-03T22:52:48,1.99,0.0
A099,C0733,L060,"List(List(I0382, Magazine Pasta, 27.07, 5), List(I0443, He Coffee, 27.38, 1))",db928d06-b658-4d7d-861c-f927279dcd25,en route,wallet,R058,2024-01-09T17:38:04,4.54,162.73
A310,C1979,L084,"List(List(I0113, Have Tea, 15.94, 2))",e19ce7b0-9806-45a4-8ec0-fec82e3b199c,en route,UPI,R043,2024-01-02T04:38:41,0.01,31.88
A393,C1523,L007,"List(List(I0495, Operation Tea, 22.44, 1), List(I0149, Wide Brownie, 8.08, 1))",3cae86ec-e526-4900-8d0d-968eea9fae55,cancelled,card,R140,2024-01-27T13:03:12,4.78,30.52
A008,C0373,L086,"List(List(I0469, Change Ice Cream, 13.1, 2), List(I0352, Movie Juice, 9.26, 1))",a8415bbb-24e8-453f-8e3a-77bbda19de58,en route,cash,R179,2024-01-16T18:35:31,3.61,35.46
A206,C5037,L088,"List(List(I0462, Their Garlic Bread, 26.4, 2))",3d0f1227-1f7a-45c9-8480-fe77b89bf5ba,preparing,UPI,R129,2024-01-04T10:07:16,1.79,52.8


In [0]:
SELECT
    item.item_id,
    item.item_name,
    SUM(item.quantity) AS total_quantity_ordered
FROM orders_bronze
LATERAL VIEW explode(items_ordered) t AS item
GROUP BY
    item.item_id,
    item.item_name
ORDER BY total_quantity_ordered DESC;

item_id,item_name,total_quantity_ordered
I0357,Argue Cake,345
I0254,Sell Ice Cream,320
I0011,Purpose Brownie,319
I0074,Painting Coffee,313
I0255,Finish Garlic Bread,312
I0274,Even Tea,311
I0189,Market Spring Roll,309
I0145,Rich Biryani,308
I0474,Instead Spring Roll,300
I0090,Others Wrap,297


In [0]:
SELECT
    ROUND(AVG(size(items_ordered)), 2) AS avg_items_per_order
FROM orders_bronze;


avg_items_per_order
1.65


In [0]:
SELECT
    restaurant_id,
    item.item_id,
    item.item_name,
    ROUND(
        try_divide(
            SUM(item.price * item.quantity) * 100.0,
            SUM(SUM(item.price * item.quantity))
                OVER (PARTITION BY restaurant_id)
        ),
        2
    ) AS revenue_contribution_percentage
FROM orders_bronze
LATERAL VIEW explode(items_ordered) t AS item
GROUP BY
    restaurant_id,
    item.item_id,
    item.item_name
ORDER BY
    restaurant_id,
    revenue_contribution_percentage DESC;

restaurant_id,item_id,item_name,revenue_contribution_percentage
R001,I0151,Section Coffee,39.37
R001,I0056,Type Ice Cream,27.64
R001,I0115,Theory Spring Roll,11.97
R001,I0446,Question Biryani,10.6
R001,I0386,Sort Brownie,10.42
R002,I0278,Skill Coffee,40.43
R002,I0349,These Brownie,33.55
R002,I0059,Allow Pasta,26.03
R003,I0305,Cell Garlic Bread,51.26
R003,I0203,Guess Pasta,48.74


In [0]:
WITH customer_restaurant_orders AS (
    SELECT
        o.customer_id,
        res.name,
        COUNT(*) AS order_count
    FROM orders_bronze o
    JOIN restaurants_filter_bronze res
        ON o.restaurant_id = res.restaurant_id
    GROUP BY
        o.customer_id,
        res.name
),

ranked_restaurants AS (
    SELECT
        customer_id,
        name,
        order_count,
        RANK() OVER (
            PARTITION BY customer_id
            ORDER BY order_count DESC
        ) AS rnk
    FROM customer_restaurant_orders
)

SELECT
    customer_id,
    name,
    order_count
FROM ranked_restaurants
WHERE rnk = 1
ORDER BY customer_id;

customer_id,name,order_count
C0001,Spice Villa Grill,2
C0003,Spice Villa Grill,1
C0004,Pasta Palace Kitchen,1
C0004,Tasty Bites Corner,1
C0006,Pasta Palace Grill,1
C0007,Tasty Bites Hub,2
C0008,Tasty Bites Kitchen,1
C0008,Tasty Bites Hub,1
C0009,Curry Leaf Corner,1
C0009,Spice Villa Grill,1


In [0]:
WITH monthly_area_orders AS (
    SELECT
        DATE_FORMAT(o.timestamp, 'yyyy-MM') AS order_month,
        l.area,
        COUNT(*) AS order_count
    FROM orders_bronze o

    JOIN restaurants_filter_bronze r
        ON o.restaurant_id = r.restaurant_id

    JOIN locations_filter_bronze l
        ON r.location_id = l.location_id

    GROUP BY
        DATE_FORMAT(o.timestamp, 'yyyy-MM'),
        l.area
)
SELECT *
FROM monthly_area_orders
QUALIFY RANK() OVER (
    PARTITION BY order_month
    ORDER BY order_count DESC
) <= 10
ORDER BY
    order_month,
    order_count DESC;

order_month,area,order_count
2024-01,Stacy Track,201
2024-01,White Tunnel,147
2024-01,Elizabeth Locks,132
2024-01,Henderson Creek,123
2024-01,Reed Glens,108
2024-01,Torres Mountain,106
2024-01,Brennan Center,104
2024-01,Burns Burg,102
2024-01,Carpenter Views,99
2024-01,Harris Grove,99


In [0]:
select * from orders_bronze where payment_method='card' and order_status='delivered';

agent_id,customer_id,delivery_location_id,items_ordered,order_id,order_status,payment_method,restaurant_id,timestamp,tip,total_amount
A086,C5605,L089,"List(List(I0491, Talk Pasta, 10.6, 2))",e293e41d-e335-4d6b-8504-34f96140e660,delivered,card,R006,2024-01-15T14:20:24,4.5,21.2
A352,C7525,L082,"List(List(I0403, Outside Juice, 23.61, 1), List(I0018, Finish Nachos, 6.76, 5), List(I0384, Mrs Cake, 9.28, 2))",c8bd7ee7-a451-447a-811b-fd69aff36062,delivered,card,R053,2024-01-04T07:36:42,0.3,75.97
A068,C1909,L083,"List(List(I0038, Near Soda, 15.97, 4), List(I0134, Structure Wrap, 16.48, 3))",e71e1b46-c026-4913-9b58-870fde58e72b,delivered,card,R047,2024-01-13T20:37:01,4.41,113.32
A196,C3246,L022,"List(List(I0185, Today Nachos, 22.46, 5))",ede3312f-d227-42a5-a1d0-d191999abbd1,delivered,card,R136,2024-01-02T20:57:26,1.4,112.3
A202,C8344,L100,"List(List(I0160, Almost Brownie, 13.71, 4), List(I0187, Travel Tea, 7.78, 2))",7e5fb9b0-c7e0-4080-89f3-6707df2a16a4,delivered,card,R074,2024-01-25T00:13:09,3.53,70.4
A390,C3024,L051,"List(List(I0254, Sell Ice Cream, 27.41, 2))",22accf1f-f43d-4051-9240-9a971c27bf85,delivered,card,R039,2024-01-20T00:43:15,1.31,54.82
A072,C2294,L082,"List(List(I0388, Nor Brownie, 9.17, 2))",bee913bc-f4fd-44b7-8f51-229c93ef4c5d,delivered,card,R018,2024-01-19T19:54:39,0.91,18.34
A307,C8811,L024,"List(List(I0112, Run Pizza, 25.36, 1), List(I0049, Soldier Ice Cream, 21.53, 2), List(I0441, Power Biryani, 0.0, 4))",5d838bcb-e367-4734-93fe-c9a2551e440f,delivered,card,R190,2024-01-05T14:06:33,2.46,68.42
A279,C1179,L038,"List(List(I0470, Radio Brownie, 25.75, 2))",938839a3-20ac-4b3b-a9b1-fb9b364bc210,delivered,card,R159,2024-01-02T16:18:53,4.28,51.5
A157,C2504,L062,"List(List(I0066, Reason Cake, 27.3, 1), List(I0158, Third Spring Roll, 18.26, 5))",3cd888ae-1614-4d75-bd5c-037edd3684f4,delivered,card,R110,2024-01-20T11:43:04,4.19,118.6


In [0]:
SELECT
    r.cuisine,
    ROUND(AVG(o.total_amount), 2) AS avg_order_value
FROM orders_bronze o
JOIN restaurants_filter_bronze r
    ON o.restaurant_id = r.restaurant_id
GROUP BY r.cuisine
ORDER BY avg_order_value DESC;

cuisine,avg_order_value
"Thai,Chinese",160.1
"Thai,Italian,Chinese",156.68
"Mexican,American",146.19
"Mexican,Indian,Thai",144.91
"Mexican,American,Thai",143.95
"American,Mexican",123.96
"Italian,Indian,Mexican",121.05
"American,Chinese",118.95
"American,Italian",110.58
"Chinese,Mexican",109.39


In [0]:
select a.name, count(*) as order_count from  orders_bronze o join delivery_agents_filter_bronze a on o.agent_id=a.agent_id
where  o.total_amount>50
 group by a.name order by order_count desc;

name,order_count
Christopher Chase,213
Christopher Williams,171
Justin Lam,118
Charlene Morgan,112
Joan Harrison,110
Carrie Maxwell,108
John King,108
Justin Smith,106
James Osborn,104
Teresa Ryan,102


In [0]:
SELECT
    l.area AS area_name,
    ROUND(SUM(o.total_amount), 2) AS total_revenue
FROM orders_bronze o
JOIN restaurants_filter_bronze r
    ON o.restaurant_id = r.restaurant_id
JOIN locations_filter_bronze l
    ON o.delivery_location_id = l.location_id
WHERE LOWER(r.cuisine) = 'italian'
GROUP BY l.area
ORDER BY total_revenue DESC;

area_name,total_revenue
Hunt Drives,583.1
Dorothy Forest,576.35
Joseph Stream,535.9
Flores Lights,517.34
Williams Way,504.67
Lee Mountains,501.97
Julie Streets,470.57
John Plains,462.63
Hill Station,460.92
Hudson Drive,447.66


In [0]:
SELECT
    r.cuisine,
    ROUND(
        AVG(o.tip / o.total_amount) * 100,
        2
    ) AS avg_tip_to_total_ratio
FROM orders_bronze o
JOIN restaurants_filter_bronze r
    ON o.restaurant_id = r.restaurant_id
WHERE o.total_amount > 0
GROUP BY r.cuisine
ORDER BY avg_tip_to_total_ratio DESC;

cuisine,avg_tip_to_total_ratio
"Indian,Mexican,American",21.65
"Thai,American,Indian",16.6
"Chinese,Thai",15.66
"Chinese,American",10.17
"Italian,Thai,Chinese",9.07
"Chinese,Italian,Thai",9.06
"Chinese,Indian,American",8.43
"Indian,American",7.78
"Mexican,Italian,American",7.75
"Indian,American,Mexican",7.53


In [0]:
SELECT
    m.item_name,
    m.restaurant_id,
    COUNT(*) AS order_count
FROM (
    SELECT item.item_id AS item_id
    FROM orders_bronze o
    LATERAL VIEW EXPLODE(o.items_ordered) t AS item
) e
JOIN menu_items_filter_bronze m
    ON e.item_id = m.item_id
GROUP BY
    m.item_name,
    m.restaurant_id
ORDER BY order_count DESC;

item_name,restaurant_id,order_count
Argue Cake,R198,111
Purpose Brownie,R138,104
Even Tea,R090,103
Rich Biryani,R139,101
Sell Ice Cream,R039,101
Painting Coffee,R084,101
Finish Garlic Bread,R082,100
Others Wrap,R165,100
Market Spring Roll,R102,99
Student Tea,R158,99


In [0]:
SELECT
    d.agent_id,
    d.name AS agent_name,
    COUNT(DISTINCT r.cuisine) AS cuisine_count
FROM orders_bronze o
JOIN restaurants_filter_bronze r
    ON o.restaurant_id = r.restaurant_id
JOIN delivery_agents_filter_bronze d
    ON o.agent_id = d.agent_id
GROUP BY
    d.agent_id,
    d.name
ORDER BY cuisine_count DESC;

agent_id,agent_name,cuisine_count
A309,Christopher Chase,43
A360,Justin Smith,40
A393,Justin Lam,39
A207,Christopher Williams,39
A168,James Osborn,38
A138,Carrie Maxwell,37
A245,Teresa Ryan,37
A162,Jamie Jones,36
A325,Thomas Lowe,36
A212,David King,35


In [0]:
WITH customer_lifetime_value AS (
    SELECT
        c.customer_id,
        YEAR(c.signup_date) AS signup_year,
        SUM(o.total_amount) AS lifetime_value
    FROM orders_bronze o
    JOIN customer_filter_bronze c
        ON o.customer_id = c.customer_id
    GROUP BY
        c.customer_id,
        YEAR(c.signup_date)
)

SELECT
    signup_year,
    ROUND(AVG(lifetime_value), 2) AS avg_customer_lifetime_value
FROM customer_lifetime_value
GROUP BY signup_year
ORDER BY signup_year;

signup_year,avg_customer_lifetime_value
1954,175.48
1955,165.45
1956,141.81
1957,162.29
1958,163.87
1959,158.55
1960,149.33
1961,171.27
1962,155.04
1963,150.94


In [0]:
SELECT
    r.restaurant_id,
    r.name,
    l.location_id,
    l.area,
    COUNT(o.order_id) AS order_count
FROM orders_bronze o
JOIN restaurants_filter_bronze r
    ON o.restaurant_id = r.restaurant_id
JOIN locations_filter_bronze l
    ON r.location_id = l.location_id
GROUP BY
    r.restaurant_id,
    r.name,
    l.location_id,
    l.area
ORDER BY order_count DESC;

restaurant_id,name,location_id,area,order_count
R005,Tasty Bites Grill,L039,Elizabeth Locks,114
R198,Curry Leaf Kitchen,L022,White Tunnel,111
R083,Spice Villa Grill,L069,Reed Glens,108
R171,Tasty Bites Grill,L093,Copeland Parks,108
R092,Food Haven Kitchen,L057,Kimberly Points,106
R035,Spice Villa Express,L022,White Tunnel,104
R185,Food Haven Kitchen,L095,Taylor Spur,104
R180,Curry Leaf Express,L086,Harris Grove,103
R146,Spice Villa Express,L047,Andrews Heights,103
R094,Tasty Bites Grill,L047,Andrews Heights,103


In [0]:
SELECT
    l.area,
    COUNT(o.order_id) AS cancelled_orders
FROM orders_bronze o
JOIN locations_filter_bronze l
    ON o.delivery_location_id = l.location_id
WHERE LOWER(o.order_status) = 'cancelled'
GROUP BY l.area
ORDER BY cancelled_orders DESC;

area,cancelled_orders
Evans Stream,58
Elizabeth Locks,57
Flores Vista,55
Ashley Extensions,53
Hill Station,52
Padilla Mall,52
White Tunnel,51
Joshua Drive,51
Curtis Oval,51
Rodriguez Mill,51


In [0]:
SELECT
    customer_id,
    COUNT(DISTINCT restaurant_id) AS restaurant_variety
FROM orders_bronze
GROUP BY customer_id
ORDER BY restaurant_variety DESC
LIMIT 10;

customer_id,restaurant_variety
C7381,9
C0362,8
C2231,8
C1449,8
C6444,8
C6971,7
C4867,7
C0313,7
C9870,7
C4347,7


In [0]:
SELECT
    r.restaurant_id,
    r.name AS restaurant_name,
    o.customer_id,
    COUNT(*) AS repeat_order_count
FROM orders_bronze o
JOIN restaurants_filter_bronze r
    ON o.restaurant_id = r.restaurant_id
GROUP BY
    r.restaurant_id,
    r.name,
    o.customer_id
HAVING COUNT(*) > 1
ORDER BY repeat_order_count DESC;

restaurant_id,restaurant_name,customer_id,repeat_order_count
R038,Spice Villa Hub,C8626,2
R134,Pasta Palace Hub,C8978,2
R150,Pasta Palace Hub,C0119,2
R019,Curry Leaf Corner,C4924,2
R183,Curry Leaf Hub,C8099,2
R188,Food Haven Corner,C0579,2
R136,Pasta Palace Kitchen,C9836,2
R117,Spice Villa Express,C3410,2
R160,Tasty Bites Grill,C3852,2
R005,Tasty Bites Grill,C2966,2


In [0]:
SELECT
    r.cuisine,
    o.payment_method,
    COUNT(*) AS order_count
FROM orders_bronze o
JOIN restaurants_filter_bronze r
    ON o.restaurant_id = r.restaurant_id
WHERE o.total_amount > 40
GROUP BY
    r.cuisine,
    o.payment_method
ORDER BY
    r.cuisine,
    order_count DESC;

cuisine,payment_method,order_count
American,card,125
American,UPI,122
American,cash,118
American,wallet,117
"American,Chinese",UPI,46
"American,Chinese",card,46
"American,Chinese",wallet,34
"American,Chinese",cash,28
"American,Chinese,Italian",wallet,22
"American,Chinese,Italian",UPI,21
